#Data Warehousing and Business Intelligence Group Assignment

##Bronze Layer

In [0]:
%sql
-- Remove the -- below when you're creating running it for the first time
--CREATE IF NOT EXISTS CATALOG dwbi;

In [0]:
%sql
-- Remove the -- below when you're creating running it for the first time
--CREATE DATABASE dwbi.stage

In [0]:
%sql
-- Remove the -- below when you're creating running it for the first time
--CREATE VOLUME dwbi.stage.volume

###Importing done manually

In [0]:
df = spark.read.option("header", True).csv("/Volumes/dwbi/stage/volume/T_ONTIME_REPORTING.csv")
display(df)

YEAR,FL_DATE,OP_UNIQUE_CARRIER,OP_CARRIER_AIRLINE_ID,OP_CARRIER_FL_NUM,ORIGIN_AIRPORT_ID,ORIGIN,ORIGIN_CITY_NAME,ORIGIN_STATE_ABR,DEST_AIRPORT_ID,DEST,DEST_CITY_NAME,DEST_STATE_ABR,CRS_DEP_TIME,DEP_TIME,DEP_DELAY,CRS_ARR_TIME,ARR_TIME,ARR_DELAY,CANCELLED,CANCELLATION_CODE,DIVERTED,ACTUAL_ELAPSED_TIME,DISTANCE
2024,1/1/2024 12:00:00 AM,9E,20363,4814,12478,JFK,"New York, NY",NY,11433,DTW,"Detroit, MI",MI,1252,1247,-5.00,1508,1449,-19.00,0.00,null,0.00,122.00,509.00
2024,1/1/2024 12:00:00 AM,9E,20363,4815,13487,MSP,"Minneapolis, MN",MN,11042,CLE,"Cleveland, OH",OH,1015,1001,-14.00,1325,1255,-30.00,0.00,null,0.00,114.00,622.00
2024,1/1/2024 12:00:00 AM,9E,20363,4817,12478,JFK,"New York, NY",NY,14524,RIC,"Richmond, VA",VA,1415,1411,-4.00,1601,1541,-20.00,0.00,null,0.00,90.00,288.00
2024,1/1/2024 12:00:00 AM,9E,20363,4817,14524,RIC,"Richmond, VA",VA,12478,JFK,"New York, NY",NY,1650,1643,-7.00,1841,1759,-42.00,0.00,null,0.00,76.00,288.00
2024,1/1/2024 12:00:00 AM,9E,20363,4818,11433,DTW,"Detroit, MI",MI,13342,MKE,"Milwaukee, WI",WI,1015,1010,-5.00,1034,1020,-14.00,0.00,null,0.00,70.00,237.00
2024,1/1/2024 12:00:00 AM,9E,20363,4822,12451,JAX,"Jacksonville, FL",FL,12953,LGA,"New York, NY",NY,1410,1403,-7.00,1627,1603,-24.00,0.00,null,0.00,120.00,833.00
2024,1/1/2024 12:00:00 AM,9E,20363,4822,12953,LGA,"New York, NY",NY,12451,JAX,"Jacksonville, FL",FL,0955,0947,-8.00,1244,1231,-13.00,0.00,null,0.00,164.00,833.00
2024,1/1/2024 12:00:00 AM,9E,20363,4823,10994,CHS,"Charleston, SC",SC,12953,LGA,"New York, NY",NY,1140,1135,-5.00,1338,1314,-24.00,0.00,null,0.00,99.00,641.00
2024,1/1/2024 12:00:00 AM,9E,20363,4823,12953,LGA,"New York, NY",NY,10994,CHS,"Charleston, SC",SC,0815,0810,-5.00,1044,1013,-31.00,0.00,null,0.00,123.00,641.00
2024,1/1/2024 12:00:00 AM,9E,20363,4828,12397,ITH,"Ithaca/Cortland, NY",NY,12478,JFK,"New York, NY",NY,1300,1248,-12.00,1419,1355,-24.00,0.00,null,0.00,67.00,189.00


In [0]:
from pyspark.sql import functions as F

null_counts_df = df.select([
    F.sum(F.when(F.col(c).isNull(), 1).otherwise(0)).alias(c) 
    for c in df.columns
])

display(null_counts_df)

YEAR,FL_DATE,OP_UNIQUE_CARRIER,OP_CARRIER_AIRLINE_ID,OP_CARRIER_FL_NUM,ORIGIN_AIRPORT_ID,ORIGIN,ORIGIN_CITY_NAME,ORIGIN_STATE_ABR,DEST_AIRPORT_ID,DEST,DEST_CITY_NAME,DEST_STATE_ABR,CRS_DEP_TIME,DEP_TIME,DEP_DELAY,CRS_ARR_TIME,ARR_TIME,ARR_DELAY,CANCELLED,CANCELLATION_CODE,DIVERTED,ACTUAL_ELAPSED_TIME,DISTANCE
0,0,0,0,0,0,0,0,0,0,0,0,0,0,19784,19858,0,20633,21901,0,526882,0,21901,0


In [0]:
df.write.format("delta").mode("overwrite") \
    .saveAsTable("dwbi.bronze.ontime_reporting")

##JSON source

In [0]:
import requests, json

url = "https://raw.githubusercontent.com/mwgg/Airports/master/airports.json"
response = requests.get(url)
airports_data = response.json()

with open("/Volumes/dwbi/stage/volume/airports.json", "w") as f:
    json.dump(airports_data, f)

print(f"Total airports fetched: {len(airports_data)}")

Total airports fetched: 29307


In [0]:
import json
from pyspark.sql.functions import col

with open("/Volumes/dwbi/stage/volume/airports.json", "r") as f:
    airports_data = json.load(f)

jsonl_path = "/Volumes/dwbi/stage/volume/airports_jsonl"
with open(jsonl_path, "w") as f:
    for airport in airports_data.values():
        f.write(json.dumps(airport) + "\n")

df_raw = spark.read.json(jsonl_path)

df_airports = df_raw.select(
    col("name"),
    col("city"),
    col("country"),
    col("iata"),
    col("icao"),
    col("lat").cast("double").alias("latitude"),
    col("lon").cast("double").alias("longitude"),
    col("elevation").cast("double").alias("altitude"),
    col("tz")
)

display(df_airports)

name,city,country,iata,icao,latitude,longitude,altitude,tz
Lowell Field,Anchor Point,US,,00AK,59.94919968,-151.695999146,450.0,America/Anchorage
Epps Airpark,Harvest,US,,00AL,34.8647994995,-86.7703018188,820.0,America/Chicago
Cordes Airport,Cordes,US,,00AZ,34.3055992126,-112.1650009155,3810.0,America/Phoenix
Goldstone /Gts/ Airport,Barstow,US,,00CA,35.3504981995,-116.888000488,3038.0,America/Los_Angeles
Williams Ag Airport,Biggs,US,,00CL,39.42718888,-121.76342777,87.0,America/Los_Angeles
Cass Field,Briggsdale,US,,00CO,40.6222000122,-104.34400177,4830.0,America/Denver
Grass Patch Airport,Bushnell,US,,00FA,28.6455001831,-82.21900177,53.0,America/New_York
River Oak Airport,Okeechobee,US,,00FL,27.2308998108,-80.9692001343,35.0,America/New_York
Lt World Airport,Lithonia,US,,00GA,33.7675018311,-84.0682983398,700.0,America/New_York
Delta Shores Airport,Clark Fork,US,,00ID,48.1453018188,-116.2139968872,2064.0,America/Los_Angeles


In [0]:
df_airports.write.mode("overwrite") \
    .option("header", "true") \
    .csv("/Volumes/dwbi/stage/volume/Airports.csv")

In [0]:
%sql
-- CREATE DATABASE dwbi.bronze;

In [0]:
df_airports.write.format("delta").mode("overwrite") \
    .saveAsTable("dwbi.bronze.airports_lookup")

Declaring variables to display tables

In [0]:
df_flights = spark.table("dwbi.bronze.ontime_reporting")
df_airports = spark.table("dwbi.bronze.airports_lookup")

In [0]:
df_airports.show()

+--------------------+------------+-------+----+----+-------------+---------------+--------+-------------------+
|                name|        city|country|iata|icao|     latitude|      longitude|altitude|                 tz|
+--------------------+------------+-------+----+----+-------------+---------------+--------+-------------------+
|        Lowell Field|Anchor Point|     US|    |00AK|  59.94919968| -151.695999146|   450.0|  America/Anchorage|
|        Epps Airpark|     Harvest|     US|    |00AL|34.8647994995| -86.7703018188|   820.0|    America/Chicago|
|      Cordes Airport|      Cordes|     US|    |00AZ|34.3055992126|-112.1650009155|  3810.0|    America/Phoenix|
|Goldstone /Gts/ A...|     Barstow|     US|    |00CA|35.3504981995| -116.888000488|  3038.0|America/Los_Angeles|
| Williams Ag Airport|       Biggs|     US|    |00CL|  39.42718888|  -121.76342777|    87.0|America/Los_Angeles|
|          Cass Field|  Briggsdale|     US|    |00CO|40.6222000122|  -104.34400177|  4830.0|    

In [0]:
df_flights.show()

+----+--------------------+-----------------+---------------------+-----------------+-----------------+------+--------------------+----------------+---------------+----+--------------------+--------------+------------+--------+---------+------------+--------+---------+---------+-----------------+--------+-------------------+--------+
|YEAR|             FL_DATE|OP_UNIQUE_CARRIER|OP_CARRIER_AIRLINE_ID|OP_CARRIER_FL_NUM|ORIGIN_AIRPORT_ID|ORIGIN|    ORIGIN_CITY_NAME|ORIGIN_STATE_ABR|DEST_AIRPORT_ID|DEST|      DEST_CITY_NAME|DEST_STATE_ABR|CRS_DEP_TIME|DEP_TIME|DEP_DELAY|CRS_ARR_TIME|ARR_TIME|ARR_DELAY|CANCELLED|CANCELLATION_CODE|DIVERTED|ACTUAL_ELAPSED_TIME|DISTANCE|
+----+--------------------+-----------------+---------------------+-----------------+-----------------+------+--------------------+----------------+---------------+----+--------------------+--------------+------------+--------+---------+------------+--------+---------+---------+-----------------+--------+-------------------+--

In [0]:
%sql
SELECT
    DISTINCT ORIGIN_AIRPORT_ID, ORIGIN_CITY_NAME
FROM
    dwbi.bronze.ontime_reporting;

ORIGIN_AIRPORT_ID,ORIGIN_CITY_NAME
10529,"Hartford, CT"
11267,"Dayton, OH"
13577,"Myrtle Beach, SC"
14321,"Portland, ME"
14783,"Springfield, MO"
10792,"Buffalo, NY"
10208,"Augusta, GA"
12173,"Honolulu, HI"
11278,"Washington, DC"
10140,"Albuquerque, NM"


In [0]:
from pyspark.sql import functions as F

origin_codes = df_flights.select(F.col("ORIGIN").alias("code")).distinct()
unmatched = origin_codes.join(df_airports, origin_codes.code == df_airports.iata, "left_anti")

print(f"Unmatched ORIGIN codes: {unmatched.count()} out of {origin_codes.count()}")
display(unmatched)

Unmatched ORIGIN codes: 0 out of 334


code
